In [0]:
import pyspark.sql.functions as F
import pyspark.sql.types as T

## Brands

In [0]:
catalog_name = 'ecommerce'
df_bronze = spark.read.table(f'{catalog_name}.bronze.brz_brands')
df_bronze.show()

+--------+--------------+-------------+--------------------+--------------------+
|brand_id|    brand_name|category_code|         ingested_at|         source_file|
+--------+--------------+-------------+--------------------+--------------------+
|    ACME|      AcmeTech|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    NOVW|     NovaWave |           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    ZNTH|        Zenith|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    BYTM|       ByteMax|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    ECOT|       EcoTone|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    SKYL|       SkyLink|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|   VOLT@|      VoltEdge|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    PHTX|      Photonix|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    URTL|    UrbanTrail|          APP|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    COTC|    Co

In [0]:
df_silver = df_bronze.withColumn('brand_name',F.trim(F.col('brand_name')))
df_silver.show()

+--------+-----------+-------------+--------------------+--------------------+
|brand_id| brand_name|category_code|         ingested_at|         source_file|
+--------+-----------+-------------+--------------------+--------------------+
|    ACME|   AcmeTech|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    NOVW|   NovaWave|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    ZNTH|     Zenith|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    BYTM|    ByteMax|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    ECOT|    EcoTone|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    SKYL|    SkyLink|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|   VOLT@|   VoltEdge|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    PHTX|   Photonix|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    URTL| UrbanTrail|          APP|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    COTC| CottonClub|          APP|2026-09-17 11:41

In [0]:
df_silver = df_silver.withColumn('brand_id',F.regexp_replace(F.col('brand_id'),r'[^A-Za-z0-9]',''))

In [0]:
df_silver.show()

+--------+-----------+-------------+--------------------+--------------------+
|brand_id| brand_name|category_code|         ingested_at|         source_file|
+--------+-----------+-------------+--------------------+--------------------+
|    ACME|   AcmeTech|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    NOVW|   NovaWave|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    ZNTH|     Zenith|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    BYTM|    ByteMax|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    ECOT|    EcoTone|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    SKYL|    SkyLink|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    VOLT|   VoltEdge|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    PHTX|   Photonix|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    URTL| UrbanTrail|          APP|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    COTC| CottonClub|          APP|2026-09-17 11:41

In [0]:
df_silver.select('category_code').distinct().show()

+-------------+
|category_code|
+-------------+
|           CE|
|          APP|
|          HNK|
|          BPC|
|        BOOKS|
|          BKS|
|      GROCERY|
|         GRCY|
|          TOY|
|         TOYS|
|          SPT|
+-------------+



In [0]:
anomalies = {
    'BOOKS':'BKS',
    'GROCERY':'GRCY'
    
}
'''df_silver = df_silver.withColumn('category_code', F.when(F.col('category_code') == 'BOOKS', 'BKS')
                                                       .when(F.col('category_code') == 'GROCERY', 'GRCY')
                                                       .otherwise(F.col('category_code')))
                                                       '''
df_silver = df_silver.replace(to_replace=anomalies,subset=['category_code'])
df_silver.show()
ann = {
    'TOYS':'TOY'
}
df_silver = df_silver.replace(to_replace=ann, subset=['category_code'])
df_silver.select('category_code').distinct().show()

+--------+-----------+-------------+--------------------+--------------------+
|brand_id| brand_name|category_code|         ingested_at|         source_file|
+--------+-----------+-------------+--------------------+--------------------+
|    ACME|   AcmeTech|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    NOVW|   NovaWave|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    ZNTH|     Zenith|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    BYTM|    ByteMax|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    ECOT|    EcoTone|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    SKYL|    SkyLink|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    VOLT|   VoltEdge|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    PHTX|   Photonix|           CE|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    URTL| UrbanTrail|          APP|2026-09-17 11:41:...|dbfs:/Volumes/eco...|
|    COTC| CottonClub|          APP|2026-09-17 11:41

In [0]:
df_silver.write.format('delta')\
    .mode('overwrite')\
        .option('mergeSchema','true')\
            .saveAsTable(f'{catalog_name}.silver.slv_brands')

## Category

In [0]:
df_bronze = spark.table(f'{catalog_name}.bronze.brz_category')
df_bronze.show(truncate = False, vertical = True)


-RECORD 0----------------------------------------------------------------------
 category_name | ce                                                            
 category_code | Electronics                                                   
 ingested_at   | 2026-09-17 11:42:11.930072                                    
 source_file   | dbfs:/Volumes/ecommerce/source_data/raw/category/category.csv 
-RECORD 1----------------------------------------------------------------------
 category_name | app                                                           
 category_code | Apparel                                                       
 ingested_at   | 2026-09-17 11:42:11.930072                                    
 source_file   | dbfs:/Volumes/ecommerce/source_data/raw/category/category.csv 
-RECORD 2----------------------------------------------------------------------
 category_name | hnk                                                           
 category_code | Home & Kitchen         

In [0]:
df_duplicates = df_bronze.groupBy('category_name').count().filter(F.col('count')>1)
df_duplicates.show()

+-------------+-----+
|category_name|count|
+-------------+-----+
|          app|    2|
|         grcy|    2|
+-------------+-----+



In [0]:
df_silver = df_bronze.drop_duplicates(['category_name'])
df_silver.groupBy("category_name").count().show()

+-------------+-----+
|category_name|count|
+-------------+-----+
|           ce|    1|
|          app|    1|
|          hnk|    1|
|          bpc|    1|
|          bks|    1|
|         grcy|    1|
|          toy|    1|
|          spt|    1|
+-------------+-----+



In [0]:
df_silver.show(10)

+-------------+--------------------+--------------------+--------------------+
|category_name|       category_code|         ingested_at|         source_file|
+-------------+--------------------+--------------------+--------------------+
|           ce|         Electronics|2026-09-17 11:42:...|dbfs:/Volumes/eco...|
|          app|             Apparel|2026-09-17 11:42:...|dbfs:/Volumes/eco...|
|          hnk|      Home & Kitchen|2026-09-17 11:42:...|dbfs:/Volumes/eco...|
|          bpc|Beauty & Personal...|2026-09-17 11:42:...|dbfs:/Volumes/eco...|
|          bks|               Books|2026-09-17 11:42:...|dbfs:/Volumes/eco...|
|         grcy|             Grocery|2026-09-17 11:42:...|dbfs:/Volumes/eco...|
|          toy|        Toys & Games|2026-09-17 11:42:...|dbfs:/Volumes/eco...|
|          spt|   Sports & Outdoors|2026-09-17 11:42:...|dbfs:/Volumes/eco...|
+-------------+--------------------+--------------------+--------------------+



In [0]:
df_silver = df_silver.withColumnRenamed('category_name', 'temp_category_name')\
                     .withColumnRenamed('category_code', 'category_name')\
                     .withColumnRenamed('temp_category_name', 'category_code')

In [0]:
df_silver.show()

+-------------+--------------------+--------------------+--------------------+
|category_code|       category_name|         ingested_at|         source_file|
+-------------+--------------------+--------------------+--------------------+
|           ce|         Electronics|2026-09-17 11:42:...|dbfs:/Volumes/eco...|
|          app|             Apparel|2026-09-17 11:42:...|dbfs:/Volumes/eco...|
|          hnk|      Home & Kitchen|2026-09-17 11:42:...|dbfs:/Volumes/eco...|
|          bpc|Beauty & Personal...|2026-09-17 11:42:...|dbfs:/Volumes/eco...|
|          bks|               Books|2026-09-17 11:42:...|dbfs:/Volumes/eco...|
|         grcy|             Grocery|2026-09-17 11:42:...|dbfs:/Volumes/eco...|
|          toy|        Toys & Games|2026-09-17 11:42:...|dbfs:/Volumes/eco...|
|          spt|   Sports & Outdoors|2026-09-17 11:42:...|dbfs:/Volumes/eco...|
+-------------+--------------------+--------------------+--------------------+



In [0]:
df_silver = df_silver.withColumn('category_code',F.upper(F.col('category_code')))
display(df_silver)

category_code,category_name,ingested_at,source_file
CE,Electronics,2026-09-17T11:42:11.930Z,dbfs:/Volumes/ecommerce/source_data/raw/category/category.csv
APP,Apparel,2026-09-17T11:42:11.930Z,dbfs:/Volumes/ecommerce/source_data/raw/category/category.csv
HNK,Home & Kitchen,2026-09-17T11:42:11.930Z,dbfs:/Volumes/ecommerce/source_data/raw/category/category.csv
BPC,Beauty & Personal Care,2026-09-17T11:42:11.930Z,dbfs:/Volumes/ecommerce/source_data/raw/category/category.csv
BKS,Books,2026-09-17T11:42:11.930Z,dbfs:/Volumes/ecommerce/source_data/raw/category/category.csv
GRCY,Grocery,2026-09-17T11:42:11.930Z,dbfs:/Volumes/ecommerce/source_data/raw/category/category.csv
TOY,Toys & Games,2026-09-17T11:42:11.930Z,dbfs:/Volumes/ecommerce/source_data/raw/category/category.csv
SPT,Sports & Outdoors,2026-09-17T11:42:11.930Z,dbfs:/Volumes/ecommerce/source_data/raw/category/category.csv


In [0]:
df_silver.write.format('delta')\
    .mode('overwrite')\
        .option('mergeSchema','true')\
            .saveAsTable(f"{catalog_name}.silver.slv_category")

## Customers

In [0]:
df_bronze = spark.table(f"{catalog_name}.bronze.brz_customers")
display(df_bronze,10)

customer_id,phone,country_code,country,state,ingested_at,source_file
CUST000000000001,917280033536.0,IN,India,MH,2026-09-17T11:43:28.716Z,dbfs:/Volumes/ecommerce/source_data/raw/customers/customers.csv
CUST000000000002,619489725433.0,AU,Australia,VIC,2026-09-17T11:43:28.716Z,dbfs:/Volumes/ecommerce/source_data/raw/customers/customers.csv
CUST000000000003,919390066524.0,IN,India,TN,2026-09-17T11:43:28.716Z,dbfs:/Volumes/ecommerce/source_data/raw/customers/customers.csv
CUST000000000004,917073741793.0,IN,India,TN,2026-09-17T11:43:28.716Z,dbfs:/Volumes/ecommerce/source_data/raw/customers/customers.csv
CUST000000000005,618478772532.0,AU,Australia,WA,2026-09-17T11:43:28.716Z,dbfs:/Volumes/ecommerce/source_data/raw/customers/customers.csv
CUST000000000006,916441718520.0,IN,India,GJ,2026-09-17T11:43:28.716Z,dbfs:/Volumes/ecommerce/source_data/raw/customers/customers.csv
CUST000000000007,null,IN,India,MH,2026-09-17T11:43:28.716Z,dbfs:/Volumes/ecommerce/source_data/raw/customers/customers.csv
CUST000000000008,446806361276.0,GB,United Kingdom,ENG,2026-09-17T11:43:28.716Z,dbfs:/Volumes/ecommerce/source_data/raw/customers/customers.csv
CUST000000000009,18191801729.0,US,United States,MA,2026-09-17T11:43:28.716Z,dbfs:/Volumes/ecommerce/source_data/raw/customers/customers.csv
CUST000000000010,null,IN,India,RJ,2026-09-17T11:43:28.716Z,dbfs:/Volumes/ecommerce/source_data/raw/customers/customers.csv


In [0]:
row_count, column_count = df_bronze.count(), len(df_bronze.columns)
print(f"Number of rows: {row_count}")
print(f"Number of columns: {column_count}")


Number of rows: 300000
Number of columns: 7


In [0]:
df_bronze.filter(F.col("customer_id").isNull()).count()

300

In [0]:
df_silver = df_bronze.dropna(subset=['customer_id'])
df_silver.filter(F.col('customer_id').isNull()).count()
row_count = df_silver.count()
display(row_count)

299700

In [0]:
df_silver.filter(F.col("phone").isNull()).count()

29964

In [0]:
df_silver = df_silver.fillna('Not Available',subset=['phone'])
df_silver.filter(F.col("phone").isNull()).show()


+-----------+-----+------------+-------+-----+-----------+-----------+
|customer_id|phone|country_code|country|state|ingested_at|source_file|
+-----------+-----+------------+-------+-----+-----------+-----------+
+-----------+-----+------------+-------+-----+-----------+-----------+



In [0]:
df_silver.write.format('delta')\
    .mode('overwrite')\
        .option('mergeSchema','true')\
            .saveAsTable(f"{catalog_name}.silver.slv_customers")

## products

In [0]:
df_bronze = spark.table(f"{catalog_name}.bronze.brz_products")
display(df_bronze,10)
row_count, column_count = df_bronze.count(), len(df_bronze.columns)
print(f"Number of rows: {row_count}")
print(f"Number of columns: {column_count}")

product_id,sku,category_code,brand_code,color,size,material,weight_grams,length_cm,width_cm,height_cm,rating_count,file_name,ingest_timestamp
2000000000015,STCR-HNK-00001,hnk,stcr,White,One-Size,Coton,305g,"22,2",17.1,6.3,0,dbfs:/Volumes/ecommerce/source_data/raw/products/products.csv,2026-09-17T11:44:02.351Z
2000000000022,HMNS-HNK-00002,hnk,hmns,Silver,One-Size,Steel,682g,"18,2",12.3,3.7,1,dbfs:/Volumes/ecommerce/source_data/raw/products/products.csv,2026-09-17T11:44:02.351Z
2000000000039,NOVW-CE-00003,ce,novw,Purple,One-Size,Wood,243g,"18,2",13.9,4.2,0,dbfs:/Volumes/ecommerce/source_data/raw/products/products.csv,2026-09-17T11:44:02.351Z
2000000000046,URTL-APP-00004,app,urtl,Silver,S,Ruber,225g,"17,6",4.6,5.8,50,dbfs:/Volumes/ecommerce/source_data/raw/products/products.csv,2026-09-17T11:44:02.351Z
2000000000053,GGRN-GRC-00005,grcy,ggrn,Silver,One-Size,Ruber,455g,"27,2",15.8,7.4,-4,dbfs:/Volumes/ecommerce/source_data/raw/products/products.csv,2026-09-17T11:44:02.351Z
2000000000060,SLKE-BPC-00006,bpc,slke,Purple,One-Size,Plastic,232g,"28,0",13.8,6.1,0,dbfs:/Volumes/ecommerce/source_data/raw/products/products.csv,2026-09-17T11:44:02.351Z
2000000000077,VOLT-CE-00007,ce,volt,Blue,One-Size,Plastic,507g,"27,2",12.1,6.4,5,dbfs:/Volumes/ecommerce/source_data/raw/products/products.csv,2026-09-17T11:44:02.351Z
2000000000084,CBLT-APP-00008,app,cblt,Blue,XS,Polyester,261g,"27,7",8.5,7.0,0,dbfs:/Volumes/ecommerce/source_data/raw/products/products.csv,2026-09-17T11:44:02.351Z
2000000000091,ARFT-SPT-00009,spt,arft,Blue,XL,Plastic,59g,"12,5",19.0,7.9,11,dbfs:/Volumes/ecommerce/source_data/raw/products/products.csv,2026-09-17T11:44:02.351Z
2000000000107,MOSA-APP-0000A,app,mosa,White,L,Polyester,238g,"10,7",17.7,10.3,6,dbfs:/Volumes/ecommerce/source_data/raw/products/products.csv,2026-09-17T11:44:02.351Z


Number of rows: 50000
Number of columns: 14


In [0]:
df_bronze.select("weight_grams").show(5,truncate = False)

+------------+
|weight_grams|
+------------+
|305g        |
|682g        |
|243g        |
|225g        |
|455g        |
+------------+
only showing top 5 rows


In [0]:
df_silver = df_bronze.withColumn(
    'weight_grams',
    F.regexp_replace(F.col('weight_grams'), 'g','').cast(T.IntegerType())
)
df_silver.select('weight_grams').show(5,truncate = False)


+------------+
|weight_grams|
+------------+
|305         |
|682         |
|243         |
|225         |
|455         |
+------------+
only showing top 5 rows


In [0]:
df_silver.select("length_cm").show(5,truncate = False)
df_silver = df_silver.withColumn(
    'length_cm',
    F.regexp_replace(F.col('length_cm'), ',','.').cast(T.FloatType())
)
df_silver.select('length_cm').show(5,truncate = False)


+---------+
|length_cm|
+---------+
|22,2     |
|18,2     |
|18,2     |
|17,6     |
|27,2     |
+---------+
only showing top 5 rows
+---------+
|length_cm|
+---------+
|22.2     |
|18.2     |
|18.2     |
|17.6     |
|27.2     |
+---------+
only showing top 5 rows


In [0]:
df_silver.select('category_code','brand_code').show(5,truncate = False)

+-------------+----------+
|category_code|brand_code|
+-------------+----------+
|hnk          |stcr      |
|hnk          |hmns      |
|ce           |novw      |
|app          |urtl      |
|grcy         |ggrn      |
+-------------+----------+
only showing top 5 rows


In [0]:
df_silver = df_silver.withColumn('category_code',
    F.upper(F.col("category_code"))
).withColumn(
    'brand_code',
    F.upper(F.col("brand_code"))
)

In [0]:
df_silver.select('category_code','brand_code').show(5,truncate = False)

+-------------+----------+
|category_code|brand_code|
+-------------+----------+
|HNK          |STCR      |
|HNK          |HMNS      |
|CE           |NOVW      |
|APP          |URTL      |
|GRCY         |GGRN      |
+-------------+----------+
only showing top 5 rows


In [0]:
df_silver.select("material").distinct().show()

+---------+
| material|
+---------+
|   Cotton|
|    Steel|
|     Wood|
|   Rubber|
|  Plastic|
|Polyester|
|    Glass|
|Aluminium|
|    Paper|
|  Leather|
+---------+



In [0]:
# Fix spelling mistakes
df_silver = df_silver.withColumn(
    "material",
    F.when(F.col("material") == "Coton", "Cotton")
     .when(F.col("material") == "Alumium", "Aluminium")
     .when(F.col("material") == "Ruber", "Rubber")
     .otherwise(F.col("material"))
)
df_silver.select("material").distinct().show()    

+---------+
| material|
+---------+
|   Cotton|
|    Steel|
|     Wood|
|   Rubber|
|  Plastic|
|Polyester|
|    Glass|
|Aluminium|
|    Paper|
|  Leather|
+---------+



In [0]:
df_silver.select("rating_count").filter(F.col("rating_count")<0).show()

+------------+
|rating_count|
+------------+
|          -4|
|          -2|
|          -2|
|          -1|
|         -14|
|          -1|
|          -1|
|          -6|
|         -38|
|          -2|
|          -2|
|          -3|
|          -1|
|          -6|
|         -29|
|          -5|
|          -2|
|          -5|
|          -1|
|          -5|
+------------+
only showing top 20 rows


In [0]:
df_silver = df_silver.withColumn(
    'rating_count',
    F.when(F.col("rating_count").isNotNull(),F.abs(F.col("rating_count")))
)

In [0]:
df_silver.select("rating_count").filter(F.col("rating_count")<0).show()

+------------+
|rating_count|
+------------+
+------------+



In [0]:
df_silver.write.format('delta')\
    .mode('overwrite')\
        .option('mergeSchema','true')\
            .saveAsTable(f"{catalog_name}.silver.slv_products")

## Calendar/ date

In [0]:
df_bronze = spark.table(f'{catalog_name}.bronze.brz_date')
df_bronze.show()

+----------+----+---------+-------+------------+--------------------+--------------------+
|      date|year| day_name|quarter|week_of_year|         ingested_at|         source_file|
+----------+----+---------+-------+------------+--------------------+--------------------+
|01-08-2025|2025|   friday|      3|         -31|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|02-08-2025|2025| SATURDAY|      3|         -31|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|03-08-2025|2025|   SUNDAY|      3|         -31|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|04-08-2025|2025|   MONDAY|      3|         -32|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|05-08-2025|2025|  TUESDAY|      3|         -32|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|06-08-2025|2025|WEDNESDAY|      3|         -32|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|07-08-2025|2025| thursday|      3|         -32|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|08-08-2025|2025|   friday|      3|         -32|2026-09-17 11:43:...|dbfs:/Volumes/eco...|

In [0]:
df_bronze.printSchema()

root
 |-- date: string (nullable = true)
 |-- year: string (nullable = true)
 |-- day_name: string (nullable = true)
 |-- quarter: string (nullable = true)
 |-- week_of_year: string (nullable = true)
 |-- ingested_at: timestamp (nullable = true)
 |-- source_file: string (nullable = true)



In [0]:
from pyspark.sql.functions import to_date
df_silver = df_bronze.withColumn("date",to_date(df_bronze['date'],'dd-MM-yyyy'))

In [0]:
print(df_silver.printSchema())

df_silver.show(5)

root
 |-- date: date (nullable = true)
 |-- year: string (nullable = true)
 |-- day_name: string (nullable = true)
 |-- quarter: string (nullable = true)
 |-- week_of_year: string (nullable = true)
 |-- ingested_at: timestamp (nullable = true)
 |-- source_file: string (nullable = true)

None
+----------+----+--------+-------+------------+--------------------+--------------------+
|      date|year|day_name|quarter|week_of_year|         ingested_at|         source_file|
+----------+----+--------+-------+------------+--------------------+--------------------+
|2025-08-01|2025|  friday|      3|         -31|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|2025-08-02|2025|SATURDAY|      3|         -31|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|2025-08-03|2025|  SUNDAY|      3|         -31|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|2025-08-04|2025|  MONDAY|      3|         -32|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|2025-08-05|2025| TUESDAY|      3|         -32|2026-09-17 11:43:...|dbfs:/Vol

In [0]:
dulpicates = df_silver.groupBy('date').count().filter(F.col('count')>1).count()
print(f'Number of duplicates: {dulpicates}')
df_silver.write.format('delta')\
    .mode('overwrite')\
        .option('mergeSchema','true')\
            .saveAsTable(f"{catalog_name}.silver.slv_date")

Number of duplicates: 3


In [0]:
df_silver = df_silver.dropDuplicates(['date'])
row_count = df_silver.count()
print(f'Number of rows in silver table: {row_count}')

Number of rows in silver table: 92


In [0]:
df_silver = df_silver.withColumn('day_name',F.initcap(F.col("day_name")))
df_silver.show(5)

+----------+----+--------+-------+------------+--------------------+--------------------+
|      date|year|day_name|quarter|week_of_year|         ingested_at|         source_file|
+----------+----+--------+-------+------------+--------------------+--------------------+
|2025-08-01|2025|  Friday|      3|         -31|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|2025-08-02|2025|Saturday|      3|         -31|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|2025-08-03|2025|  Sunday|      3|         -31|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|2025-08-04|2025|  Monday|      3|         -32|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|2025-08-05|2025| Tuesday|      3|         -32|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
+----------+----+--------+-------+------------+--------------------+--------------------+
only showing top 5 rows


In [0]:
df_silver = df_silver.withColumn("week_of_year", F.abs(F.col("week_of_year")))  # Convert negative to positive

df_silver.show(3)

+----------+----+--------+-------+------------+--------------------+--------------------+
|      date|year|day_name|quarter|week_of_year|         ingested_at|         source_file|
+----------+----+--------+-------+------------+--------------------+--------------------+
|2025-08-01|2025|  Friday|      3|        31.0|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|2025-08-02|2025|Saturday|      3|        31.0|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|2025-08-03|2025|  Sunday|      3|        31.0|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
+----------+----+--------+-------+------------+--------------------+--------------------+
only showing top 3 rows


In [0]:
df_silver = df_silver.withColumn("quarter", F.concat_ws("", F.concat(F.lit("Q"), F.col("quarter"), F.lit("-"), F.col("year"))))

df_silver = df_silver.withColumn("week_of_year", F.concat_ws("-", F.concat(F.lit("Week"), F.col("week_of_year"), F.lit("-"), F.col("year"))))

df_silver.show(3)

+----------+----+--------+-------------+--------------------+--------------------+--------------------+
|      date|year|day_name|      quarter|        week_of_year|         ingested_at|         source_file|
+----------+----+--------+-------------+--------------------+--------------------+--------------------+
|2025-08-01|2025|  Friday|QQ3-2025-2025|WeekWeek31.0-2025...|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|2025-08-02|2025|Saturday|QQ3-2025-2025|WeekWeek31.0-2025...|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
|2025-08-03|2025|  Sunday|QQ3-2025-2025|WeekWeek31.0-2025...|2026-09-17 11:43:...|dbfs:/Volumes/eco...|
+----------+----+--------+-------------+--------------------+--------------------+--------------------+
only showing top 3 rows


In [0]:
# Rename a column
df_silver = df_silver.withColumnRenamed("week_of_year", "week")

In [0]:
# Write raw data to the silver layer (catalog: ecommerce, schema: silver, table: slv_calendar)
df_silver.write.format("delta") \
    .mode("overwrite") \
    .option("mergeSchema", "true") \
    .saveAsTable(f"{catalog_name}.silver.slv_calendar")